In [0]:
# ============================================================
# MVP VTI CBL
# Notebook: 01_Bronze
#
# Objetivo:
# Realizar a ingestão dos arquivos Excel armazenados no Unity Catalog Volume e transformar o dados brutos como tabelas Delta na camada Bronze.
#
# Fontes:
# 1. Medições CBL
# 2. Locais de instalação
# 3. Blocos de 25 metros
# ============================================================

In [0]:
# Caminho base do Volume utilizado como camada Landing do MVP
BASE_PATH = "/Volumes/mvp_vti/landing/raw_files/"
# Diretórios das três fontes utilizadas no pipeline
PATH_CBL = BASE_PATH + "cbl/"
PATH_LOCAIS = BASE_PATH + "locais/"
PATH_BLOCOS = BASE_PATH + "blocos/"

In [0]:
# Valida os caminhos definidos para as três fontes antes da leitura dos arquivos
print("Caminho CBL:", PATH_CBL)
print("Caminho Locais:", PATH_LOCAIS)
print("Caminho Blocos:", PATH_BLOCOS)

Caminho CBL: /Volumes/mvp_vti/landing/raw_files/cbl/
Caminho Locais: /Volumes/mvp_vti/landing/raw_files/locais/
Caminho Blocos: /Volumes/mvp_vti/landing/raw_files/blocos/


In [0]:
# Realiza a leitura dos arquivos CBL disponíveis na camada Landing
# O cabeçalho da planilha é considerado a partir da primeira linha
df_cbl = spark.read.option("headerRows", 1).excel(PATH_CBL)
# Exibe uma amostra dos dados para validar a leitura e a estrutura da fonte
display(df_cbl)

id,subdivision,linecode,track_no,km_major,kp_minor,latitude,longitude,date_time,sys,type,value,length,severity,system_review_status,vehicle,speed,heading,direction
26,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5780170000000000,-44.348227999999999,2025-03-15T11:55:00.000,VTI,CBL-PEAK,0.12000000000000000,null,Priority,Confirmed,263,24,268,N/A
32,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5781079999999998,-44.346722000000000,2025-03-15T11:55:00.000,VTI,CBL-PEAK,0.14000000000000001,null,Priority,Confirmed,263,27,272,N/A
34,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5780500000000002,-44.347712999999999,2025-03-15T11:55:00.000,VTI,CBL-PEAK,0.11000000000000000,null,Priority,Confirmed,263,25,275,N/A
40,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5780850000000002,-44.347110000000001,2025-03-15T11:55:00.000,VTI,CBL-PEAK,0.11000000000000000,null,Priority,Confirmed,263,27,275,N/A
46,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5780249999999998,-44.347973000000003,2025-03-15T11:55:00.000,VTI,CBL-PEAK,0.17000000000000000,null,Priority,Confirmed,263,25,276,N/A
47,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5780180000000001,-44.348089999999999,2025-03-15T11:55:00.000,VTI,CBL-PEAK,0.12000000000000000,null,Priority,Confirmed,263,25,274,N/A
53,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5781529999999999,-44.346077000000001,2025-03-15T11:55:00.000,VTI,CBL-PEAK,0.11000000000000000,null,Priority,Confirmed,263,28,270,N/A
89,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5780599999999998,-44.329740000000001,2025-03-15T13:09:00.000,VTI,CBL-PEAK,0.11000000000000000,null,Priority,Confirmed,263,24,90,N/A
98,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5781499999999999,-44.328403000000002,2025-03-15T13:09:00.000,VTI,CBL-PEAK,0.12000000000000000,null,Priority,Confirmed,263,27,91,N/A
105,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5781499999999999,-44.327713000000003,2025-03-15T13:09:00.000,VTI,CBL-PEAK,0.13000000000000000,null,Priority,Confirmed,263,28,90,N/A


In [0]:
# Importa as funções do PySpark utilizadas nas transformações da camada Bronze
from pyspark.sql import functions as F
# Mantém os dados de origem e adiciona informações para rastreabilidade da ingestão
df_cbl_bronze = (
df_cbl
.withColumn("_ingestion_ts", F.current_timestamp())
.withColumn("_source", F.lit("excel_cbl"))
)
# Valida visualmente os dados após a inclusão dos metadados da camada Bronze
display(df_cbl_bronze)

id,subdivision,linecode,track_no,km_major,kp_minor,latitude,longitude,date_time,sys,type,value,length,severity,system_review_status,vehicle,speed,heading,direction,_ingestion_ts,_source
26,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5780170000000000,-44.348227999999999,2025-03-15T11:55:00.000,VTI,CBL-PEAK,0.12000000000000000,null,Priority,Confirmed,263,24,268,N/A,2026-09-27T16:00:44.306Z,excel_cbl
32,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5781079999999998,-44.346722000000000,2025-03-15T11:55:00.000,VTI,CBL-PEAK,0.14000000000000001,null,Priority,Confirmed,263,27,272,N/A,2026-09-27T16:00:44.306Z,excel_cbl
34,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5780500000000002,-44.347712999999999,2025-03-15T11:55:00.000,VTI,CBL-PEAK,0.11000000000000000,null,Priority,Confirmed,263,25,275,N/A,2026-09-27T16:00:44.306Z,excel_cbl
40,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5780850000000002,-44.347110000000001,2025-03-15T11:55:00.000,VTI,CBL-PEAK,0.11000000000000000,null,Priority,Confirmed,263,27,275,N/A,2026-09-27T16:00:44.306Z,excel_cbl
46,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5780249999999998,-44.347973000000003,2025-03-15T11:55:00.000,VTI,CBL-PEAK,0.17000000000000000,null,Priority,Confirmed,263,25,276,N/A,2026-09-27T16:00:44.306Z,excel_cbl
47,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5780180000000001,-44.348089999999999,2025-03-15T11:55:00.000,VTI,CBL-PEAK,0.12000000000000000,null,Priority,Confirmed,263,25,274,N/A,2026-09-27T16:00:44.306Z,excel_cbl
53,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5781529999999999,-44.346077000000001,2025-03-15T11:55:00.000,VTI,CBL-PEAK,0.11000000000000000,null,Priority,Confirmed,263,28,270,N/A,2026-09-27T16:00:44.306Z,excel_cbl
89,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5780599999999998,-44.329740000000001,2025-03-15T13:09:00.000,VTI,CBL-PEAK,0.11000000000000000,null,Priority,Confirmed,263,24,90,N/A,2026-09-27T16:00:44.306Z,excel_cbl
98,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5781499999999999,-44.328403000000002,2025-03-15T13:09:00.000,VTI,CBL-PEAK,0.12000000000000000,null,Priority,Confirmed,263,27,91,N/A,2026-09-27T16:00:44.306Z,excel_cbl
105,UNKNOWN,UNKNOWN,UNKNOWN,null,null,-2.5781499999999999,-44.327713000000003,2025-03-15T13:09:00.000,VTI,CBL-PEAK,0.13000000000000000,null,Priority,Confirmed,263,28,90,N/A,2026-09-27T16:00:44.306Z,excel_cbl


In [0]:
# Grava a base CBL enriquecida com metadados como tabela Delta na camada Bronze
# O modo overwrite garante que a tabela seja atualizada a cada execução do pipeline
(
df_cbl_bronze.write
.format("delta")
.mode("overwrite")
.saveAsTable("mvp_vti.bronze.bronze_cbl_raw")
)


In [0]:
# Realiza a leitura dos arquivos de locais disponíveis na camada Landing
# O cabeçalho da planilha é considerado a partir da primeira linha
df_locais = spark.read.option("headerRows", 1).excel(PATH_LOCAIS)
# Exibe uma amostra dos dados para validar a leitura e os campos de localização ferroviária
display(df_locais)

taxonomia,linha,ponto_partida,ponto_final
SEG-VF - E000000-L0001-CDV1E1T,LP001,0,205
SEG-VF - E000000-L0002-CDV2E1T,LP002,0,370
SEG-VF - E000000-L0001-CDVTE01,LP001,205,370
SEG-VF - TU00000-L0001-CDVW01T,LP001,370,830
SEG-VF - TU00000-L0002-CDVW02T,LP002,370,830
SEG-VF - E000007-L0001-CDV1D1T,LP001,830,4480
SEG-VF - E000007-L0002-CDV2D1T,LP002,830,4480
SEG-VF - E000007-L0001-CDV1E1T,LP001,4480,7170
SEG-VF - E000007-L0002-CDV2E1T,LP002,4480,7170
SEG-VF - TU00007-L0001-CDVW01T,LP001,7170,7630


In [0]:
# Mantém os dados originais de Locais e adiciona informações de rastreabilidade da ingestão
df_locais_bronze = (
df_locais
.withColumn("_ingestion_ts", F.current_timestamp())
.withColumn("_source", F.lit("excel_locais"))
)
# Valida visualmente a estrutura da base após a inclusão dos metadados da camada Bronze
display(df_locais_bronze)

taxonomia,linha,ponto_partida,ponto_final,_ingestion_ts,_source
SEG-VF - E000000-L0001-CDV1E1T,LP001,0,205,2026-09-27T16:04:14.631Z,excel_locais
SEG-VF - E000000-L0002-CDV2E1T,LP002,0,370,2026-09-27T16:04:14.631Z,excel_locais
SEG-VF - E000000-L0001-CDVTE01,LP001,205,370,2026-09-27T16:04:14.631Z,excel_locais
SEG-VF - TU00000-L0001-CDVW01T,LP001,370,830,2026-09-27T16:04:14.631Z,excel_locais
SEG-VF - TU00000-L0002-CDVW02T,LP002,370,830,2026-09-27T16:04:14.631Z,excel_locais
SEG-VF - E000007-L0001-CDV1D1T,LP001,830,4480,2026-09-27T16:04:14.631Z,excel_locais
SEG-VF - E000007-L0002-CDV2D1T,LP002,830,4480,2026-09-27T16:04:14.631Z,excel_locais
SEG-VF - E000007-L0001-CDV1E1T,LP001,4480,7170,2026-09-27T16:04:14.631Z,excel_locais
SEG-VF - E000007-L0002-CDV2E1T,LP002,4480,7170,2026-09-27T16:04:14.631Z,excel_locais
SEG-VF - TU00007-L0001-CDVW01T,LP001,7170,7630,2026-09-27T16:04:14.631Z,excel_locais


In [0]:
# Grava a base de Locais enriquecida com metadados como tabela Delta na camada Bronze
# O modo overwrite permite atualizar a tabela sempre que o pipeline for executado novamente
(
df_locais_bronze.write
.format("delta")
.mode("overwrite")
.saveAsTable("mvp_vti.bronze.bronze_locais_raw")
)

In [0]:
# Realiza a leitura dos arquivos de blocos de 25 m disponíveis na camada Landing
# O cabeçalho da planilha é considerado a partir da primeira linha
df_blocos = spark.read.option("headerRows", 1).excel(PATH_BLOCOS)
# Exibe uma amostra para validar a leitura e os campos que definem os intervalos dos blocos
display(df_blocos)

linha,km_inicio,km_fim
LP001,0E-18,0.025000000000000001
LP001,0.025000000000000001,0.050000000000000000
LP001,0.050000000000000000,0.074999999999999997
LP001,0.074999999999999997,0.100000000000000000
LP001,0.100000000000000000,0.125000000000000000
LP001,0.125000000000000000,0.150000000000000000
LP001,0.150000000000000000,0.174999999999999990
LP001,0.174999999999999990,0.200000000000000000
LP001,0.200000000000000000,0.225000000000000010
LP001,0.225000000000000010,0.250000000000000000


In [0]:
# Mantém os dados originais dos blocos de 25 m e adiciona informações de rastreabilidade da ingestão
df_blocos_bronze = (
df_blocos
.withColumn("_ingestion_ts", F.current_timestamp())
.withColumn("_source", F.lit("excel_blocos_25m"))
)
# Valida visualmente a estrutura da base após a inclusão dos metadados da camada Bronze
display(df_blocos_bronze)

linha,km_inicio,km_fim,_ingestion_ts,_source
LP001,0E-18,0.025000000000000001,2026-09-27T16:06:16.425Z,excel_blocos_25m
LP001,0.025000000000000001,0.050000000000000000,2026-09-27T16:06:16.425Z,excel_blocos_25m
LP001,0.050000000000000000,0.074999999999999997,2026-09-27T16:06:16.425Z,excel_blocos_25m
LP001,0.074999999999999997,0.100000000000000000,2026-09-27T16:06:16.425Z,excel_blocos_25m
LP001,0.100000000000000000,0.125000000000000000,2026-09-27T16:06:16.425Z,excel_blocos_25m
LP001,0.125000000000000000,0.150000000000000000,2026-09-27T16:06:16.425Z,excel_blocos_25m
LP001,0.150000000000000000,0.174999999999999990,2026-09-27T16:06:16.425Z,excel_blocos_25m
LP001,0.174999999999999990,0.200000000000000000,2026-09-27T16:06:16.425Z,excel_blocos_25m
LP001,0.200000000000000000,0.225000000000000010,2026-09-27T16:06:16.425Z,excel_blocos_25m
LP001,0.225000000000000010,0.250000000000000000,2026-09-27T16:06:16.425Z,excel_blocos_25m


In [0]:
# Grava a base de Blocos de 25 m enriquecida com metadados como tabela Delta na camada Bronze
# O modo overwrite permite atualizar a tabela sempre que o pipeline for executado novamente
(
df_blocos_bronze.write
.format("delta")
.mode("overwrite")
.saveAsTable("mvp_vti.bronze.bronze_blocos_raw")
)

In [0]:
# Lista as tabelas criadas na camada Bronze para validação após a persistência
tabelas = [
"mvp_vti.bronze.bronze_cbl_raw",
"mvp_vti.bronze.bronze_locais_raw",
"mvp_vti.bronze.bronze_blocos_raw"
]
# Confere a quantidade de registros gravados em cada tabela
# Esta validação confirma que as três fontes foram materializadas corretamente na camada Bronze
for tabela in tabelas:
    qtd = spark.table(tabela).count()
    print(f"{tabela}: {qtd} registros")

mvp_vti.bronze.bronze_cbl_raw: 198239 registros
mvp_vti.bronze.bronze_locais_raw: 797 registros
mvp_vti.bronze.bronze_blocos_raw: 78160 registros


In [0]:
# Confere as colunas disponíveis em cada base antes de seguir para as etapas de tratamento
print("=== CBL ===")
print(df_cbl_bronze.columns)
print("\n=== LOCAIS ===")
print(df_locais_bronze.columns)
print("\n=== BLOCOS 25M ===")
print(df_blocos_bronze.columns)

=== CBL ===
['id', 'subdivision', 'linecode', 'track_no', 'km_major', 'kp_minor', 'latitude', 'longitude', 'date_time', 'sys', 'type', 'value', 'length', 'severity', 'system_review_status', 'vehicle', 'speed', 'heading', 'direction', '_ingestion_ts', '_source']

=== LOCAIS ===
['taxonomia', 'linha', 'ponto_partida', 'ponto_final', '_ingestion_ts', '_source']

=== BLOCOS 25M ===
['linha', 'km_inicio', 'km_fim', '_ingestion_ts', '_source']
